# Visualisation des études — Guidance, XGR et Outlines

Notebook principal pour consulter **l'EDA, les features raffinées, les modèles retenus, leurs scores et matrices de confusion, les arbres explicatifs et leurs règles, puis Kubernetes**.

Les résultats enregistrés sont consultables sans réentraîner de modèle. Les cellules de prédiction peuvent également **réexécuter les modèles retenus**, sur leur partition de test et sur Kubernetes. Les recalculs sont affichés séparément des scores historiques.

Les modèles prédictifs principaux et les arbres explicatifs sont deux objets distincts. `DATASET_CHOICE` pilote l'EDA et les analyses raffinées ; il ne change pas la partition des modèles GitHub. Les modèles entraînés sur Kubernetes constituent une expérience séparée de l'évaluation externe.

Voir les guides [results](results/README.md), [coverage_prediction](coverage_prediction/README.md) et [scripts](scripts/README.md).


## 1. Paramètres

Choisissez un ou plusieurs frameworks. `global` correspond à `Github_global` pour Guidance/XGR et `Github_global_no_hard` pour Outlines. `Kubernetes` est également accepté, ainsi que les datasets GitHub individuels.

Laissez les options de régénération désactivées pour consulter les sorties existantes. Si activées, elles écrivent seulement dans `notebook_outputs/`. L'extraction V1 n'est pas relancée : son module est actuellement absent. Les tables V1 disponibles restent consultables et utilisables pour recalculer la V2.


In [1]:
from pathlib import Path
import csv
import html
import json
import subprocess
import sys
from IPython.display import HTML, Markdown, display

DATASET_CHOICE = "global"
FRAMEWORKS = ["guidance", "xgr", "outlines"]
TARGETS = ["under", "over"]
EXTERNAL_DATASET = "Kubernetes"
REGENERATE_EDA = False
REGENERATE_REFINED_V2 = False
RUN_MODEL_PREDICTIONS = True
RUN_EXTERNAL_PREDICTIONS = True
MAX_TABLE_ROWS = 12
# Facultatif : Python disposant des versions compatibles avec les pickles (scikit-learn 1.9.0, LightGBM).
MODEL_PYTHON = None


In [2]:
def find_extension_dir():
    for base in [Path.cwd().resolve(), *Path.cwd().resolve().parents]:
        for candidate in (base, base / "extension_jsonschemabench", base / "jsonschemabench" / "extension_jsonschemabench"):
            if (candidate / "coverage_prediction").is_dir() and (candidate / "scripts").is_dir():
                return candidate
    raise FileNotFoundError("Lancez Jupyter depuis le projet ou le dossier de l'extension.")

EXTENSION_DIR = find_extension_dir()
REPO_ROOT = EXTENSION_DIR.parent
RESULTS_ROOT = EXTENSION_DIR / "results" / "per_dataset_runs"
COVERAGE_ROOT = EXTENSION_DIR / "coverage_prediction"
MODELS_ROOT = COVERAGE_ROOT / "modeles_predictifs"
SCRIPTS_DIR = EXTENSION_DIR / "scripts"
DATA_ROOT = REPO_ROOT / "maskbench" / "data"
OUTPUT_ROOT = EXTENSION_DIR / "notebook_outputs"
V2_OUTPUT_ROOT = OUTPUT_ROOT / "refined_feature_analysis_v2"
venv_python = REPO_ROOT / ".venv" / "bin" / "python"
MODEL_PYTHON = str(MODEL_PYTHON or (venv_python if venv_python.exists() else sys.executable))
GLOBAL_DATASET_BY_FRAMEWORK = {"guidance": "Github_global", "xgr": "Github_global", "outlines": "Github_global_no_hard"}
assert FRAMEWORKS and set(FRAMEWORKS) <= set(GLOBAL_DATASET_BY_FRAMEWORK), "Framework inconnu"
assert TARGETS and set(TARGETS) <= {"under", "over"}, "Cible inconnue"

def resolve_dataset(framework, dataset_choice=None):
    choice = DATASET_CHOICE if dataset_choice is None else dataset_choice
    return GLOBAL_DATASET_BY_FRAMEWORK[framework] if choice.lower() == "global" else choice

def run_dir(framework, dataset_choice=None):
    return RESULTS_ROOT / framework / resolve_dataset(framework, dataset_choice)

print("Extension :", EXTENSION_DIR)
print("Python des modèles :", MODEL_PYTHON)


Extension : extension_jsonschemabench
Python des modèles : .venv\Scripts\python.exe


## 2. Fonctions de lecture et de présentation


In [3]:
def read_rows(path):
    if not path.is_file() or not path.stat().st_size:
        return []
    with path.open(encoding="utf-8-sig", newline="") as handle:
        return list(csv.DictReader(handle))

def show_rows(rows, title=None, limit=MAX_TABLE_ROWS):
    if title:
        display(Markdown(f"**{title}**"))
    if not rows:
        display(Markdown("Aucune ligne disponible."))
        return
    headers = list(dict.fromkeys(k for row in rows for k in row))
    shown = rows if limit is None else rows[:limit]
    table = '<div style="overflow:auto;max-height:550px"><table><thead><tr>'
    table += ''.join(f'<th>{html.escape(str(k))}</th>' for k in headers) + '</tr></thead><tbody>'
    for row in shown:
        table += '<tr>' + ''.join(f'<td>{html.escape(str(row.get(k, "")))}</td>' for k in headers) + '</tr>'
    table += '</tbody></table></div>'
    display(HTML(table))
    if len(shown) < len(rows):
        display(Markdown(f"Aperçu : {len(shown)} / {len(rows)} lignes."))

def show_csv(path, limit=MAX_TABLE_ROWS):
    if not path.is_file():
        display(Markdown(f"Fichier absent : `{path.relative_to(EXTENSION_DIR)}`"))
        return
    show_rows(read_rows(path), path.name, limit)

def show_report(path):
    if path.is_file():
        display(Markdown(path.read_text(encoding="utf-8")))
    else:
        display(Markdown(f"Rapport absent : `{path.relative_to(EXTENSION_DIR)}`"))

def show_gallery(directory, recursive=True):
    files = sorted(directory.rglob("*.svg") if recursive else directory.glob("*.svg"))
    if not files:
        display(Markdown(f"Aucun SVG : `{directory.relative_to(EXTENSION_DIR)}`"))
        return
    display(Markdown(f"{len(files)} graphiques disponibles — cliquez sur les titres pour les ouvrir."))
    for path in files:
        svg = path.read_text(encoding="utf-8")
        start = svg.find("<svg")
        if start >= 0:
            display(HTML('<details><summary>'+html.escape(str(path.relative_to(directory)))+'</summary>'+svg[start:]+'</details>'))

def show_confusions(rows, title):
    for row in rows:
        if not all(str(row.get(k, "")).strip() for k in ("tn", "fp", "fn", "tp")):
            continue
        label = f"{title} — {row.get('model', '')} {row.get('split', '')}"
        show_rows([
            {"Vérité / Prédiction": "Négatif (pas d'erreur)", "Négatif": row["tn"], "Positif": row["fp"]},
            {"Vérité / Prédiction": "Positif (UNDER ou OVER)", "Négatif": row["fn"], "Positif": row["tp"]},
        ], label)

# Inventaire du périmètre choisi ; l'absence de plots ne signifie pas absence de run.
show_rows([{
    "framework": fw, "dataset EDA": resolve_dataset(fw),
    "résultats par test": (run_dir(fw) / "per_test_results.jsonl").exists(),
    "plots EDA": (run_dir(fw) / "plots").exists(),
    "tables raffinées": (run_dir(fw) / "refined_feature_analysis" / "refined_test_features.csv").exists(),
    "modèles": (MODELS_ROOT / fw).exists(),
} for fw in FRAMEWORKS])


framework,dataset EDA,résultats par test,plots EDA,tables raffinées,modèles
guidance,Github_global,True,True,True,True
xgr,Github_global,True,True,True,True
outlines,Github_global_no_hard,True,True,True,True


## 3. EDA et profilage, par framework

Affichage des statistiques et de **tous les graphiques disponibles**, y compris les timeouts, erreurs de compilation, UNDER/OVER, tailles et temps. La régénération optionnelle produit une nouvelle analyse dans `notebook_outputs/eda/`.


In [4]:
def show_eda(framework):
    display(Markdown(f"### {framework} — {resolve_dataset(framework)}"))
    source = run_dir(framework)
    plots = source / "plots"
    if REGENERATE_EDA:
        if not (source / "per_test_results.jsonl").is_file() or not (source / "timing_profile.csv").is_file():
            display(Markdown("Régénération ignorée : résultats par test ou profilage absents."))
        else:
            generated = OUTPUT_ROOT / "eda" / framework / resolve_dataset(framework)
            cmd = [MODEL_PYTHON, str(SCRIPTS_DIR / "analyze_dataset_statistics.py"),
                   "--framework", framework, "--dataset", resolve_dataset(framework),
                   "--results-root", str(RESULTS_ROOT), "--data-root", str(DATA_ROOT), "--output-dir", str(generated)]
            result = subprocess.run(cmd, cwd=REPO_ROOT, capture_output=True, text=True)
            if result.returncode:
                display(Markdown("Échec de la régénération ; les résultats enregistrés restent consultables."))
                print(result.stderr[-3000:])
            else:
                plots = generated
    show_csv(plots / "schema_level_stats.csv")
    show_gallery(plots, recursive=False)

for framework in FRAMEWORKS:
    show_eda(framework)


### guidance — Github_global

**schema_level_stats.csv**

dataset_id,framework_id,schema_id,n_tests,n_valid_tests,n_invalid_tests,n_valid_completed,n_invalid_completed,n_completed,n_timeout,timeout_status,timeout_stage,timeout_elapsed_s,compile_grammar_s,validation_loop_mean_s,compute_mask_mean_s,commit_token_mean_s,schema_file_bytes,schema_json_chars,mean_instance_json_chars,mean_num_tokens,max_num_tokens,n_correct_accept,n_correct_reject,n_under_constraint,n_over_constraint,under_rate,over_rate,timeout_rate,coverage_rate,accuracy_completed,permissive_score,has_additionalProperties,has_allOf,has_anchor,has_anyOf,has_boolean_schema,has_const,has_contains,has_content,has_default,has_defs,has_dependentRequired,has_dependentSchemas,has_dynamicRef,has_enum,has_exclusiveMaximum,has_exclusiveMinimum,has_if_then_else,has_infinite_loop_detection,has_items,has_maxContains,has_maxItems,has_maxLength,has_maxProperties,has_maximum,has_minContains,has_minItems,has_minLength,has_minProperties,has_minimum,has_multipleOf,has_not,has_oneOf,has_pattern,has_patternProperties,has_prefixItems,has_properties,has_propertyNames,has_ref,has_required,has_type,has_unevaluatedItems,has_unevaluatedProperties,has_uniqueItems,nb_keywords,nb_properties,nb_required,schema_depth,nb_branches_combinators,nb_enum_values,nb_regex,large_enum,many_required,many_properties,deep_schema
Github_global,guidance,Github_easy---o10008.json,3,1,2,1,2,3,0,completed,,,0.000983,0.000501,0.000431667,4.36667e-05,1896,248,39.6667,10.3333,11,1,2,0,0,0,0,0,1,1,0,true,false,false,false,true,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,true,false,false,true,true,false,false,false,9,2,2,4,0,0,0,false,false,false,false
Github_global,guidance,Github_easy---o10009.json,4,1,3,1,3,4,0,completed,,,0.001919,0.00741525,0.007293,7.025e-05,4036,340,130.5,37.75,44,1,3,0,0,0,0,0,1,1,0,true,false,false,false,true,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,true,false,false,false,false,true,false,false,false,false,false,true,false,false,true,false,false,false,true,false,false,false,13,4,0,2,0,0,1,false,false,false,false
Github_global,guidance,Github_easy---o10011.json,4,2,2,2,2,4,0,completed,,,0.000867,0.001366,0.0012095,9.5e-05,3864,587,156.25,41,44,2,2,0,0,0,0,0,1,1,0,true,false,false,false,true,false,false,false,true,false,false,false,false,true,false,false,false,false,true,false,false,false,false,false,false,false,false,false,false,false,false,true,false,false,false,true,false,false,true,true,false,false,false,24,8,2,6,2,4,0,false,false,false,false
Github_global,guidance,Github_easy---o10012.json,4,1,3,1,3,4,0,completed,,,0.000734,0.0045195,0.00445475,4.05e-05,4104,386,96.5,19.75,25,1,3,0,0,0,0,0,1,1,0,true,false,false,false,true,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,true,false,false,false,false,true,false,false,false,false,false,true,false,false,true,false,false,false,true,false,false,false,12,2,0,2,0,0,2,false,false,false,false
Github_global,guidance,Github_easy---o10013.json,4,2,2,2,2,4,0,completed,,,0.002431,0.0068345,0.0065765,0.00014775,4797,750,232,57.75,69,2,2,0,0,0,0,0,1,1,0,true,false,false,false,true,false,false,false,false,false,false,false,false,true,false,false,false,false,true,false,false,true,false,false,false,false,true,false,false,false,false,true,true,false,false,true,false,false,true,true,false,false,false,30,11,4,6,2,4,1,false,false,true,false
Github_global,guidance,Github_easy---o10014.json,2,1,1,1,1,2,0,completed,,,0.000644,0.0028025,0.0025575,0.0001415,2473,287,212,61,64,1,1,0,0,0,0,0,1,1,0,true,false,false,false,true,false,false,false,false,false,false,false,false,false,false,false,false,false,true,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,true,false,false,true,true,false,false,false,13,3,3,5,0,0,0,false,false,false,false
Github_globa

Aperçu : 12 / 4960 lignes.

32 graphiques disponibles — cliquez sur les titres pour les ouvrir.

...

### outlines — Github_global_no_hard

**schema_level_stats.csv**

dataset_id,framework_id,schema_id,n_tests,n_valid_tests,n_invalid_tests,n_valid_completed,n_invalid_completed,n_completed,n_timeout,timeout_status,timeout_stage,timeout_elapsed_s,compile_grammar_s,validation_loop_mean_s,compute_mask_mean_s,commit_token_mean_s,schema_file_bytes,schema_json_chars,mean_instance_json_chars,mean_num_tokens,max_num_tokens,n_correct_accept,n_correct_reject,n_under_constraint,n_over_constraint,under_rate,over_rate,timeout_rate,coverage_rate,accuracy_completed,permissive_score,has_additionalProperties,has_allOf,has_anchor,has_anyOf,has_boolean_schema,has_const,has_contains,has_content,has_default,has_defs,has_dependentRequired,has_dependentSchemas,has_dynamicRef,has_enum,has_exclusiveMaximum,has_exclusiveMinimum,has_if_then_else,has_infinite_loop_detection,has_items,has_maxContains,has_maxItems,has_maxLength,has_maxProperties,has_maximum,has_minContains,has_minItems,has_minLength,has_minProperties,has_minimum,has_multipleOf,has_not,has_oneOf,has_pattern,has_patternProperties,has_prefixItems,has_properties,has_propertyNames,has_ref,has_required,has_type,has_unevaluatedItems,has_unevaluatedProperties,has_uniqueItems,nb_keywords,nb_properties,nb_required,schema_depth,nb_branches_combinators,nb_enum_values,nb_regex,large_enum,many_required,many_properties,deep_schema
Github_global_no_hard,outlines,Github_easy---o10008.json,3,1,2,1,2,3,0,completed,,,0.292178,0.000115,2.6e-05,3.46667e-05,1896,248,39.6667,10.3333,11,1,2,0,0,0,0,0,1,1,0,true,false,false,false,true,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,true,false,false,true,true,false,false,false,9,2,2,4,0,0,0,false,false,false,false
Github_global_no_hard,outlines,Github_easy---o10009.json,4,1,3,1,3,4,0,completed,,,7.34728,0.0510642,0.022698,0.0282872,4036,340,130.5,37.75,44,1,3,0,0,0,0,0,1,1,0,true,false,false,false,true,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,true,false,false,false,false,true,false,false,false,false,false,true,false,false,true,false,false,false,true,false,false,false,13,4,0,2,0,0,1,false,false,false,false
Github_global_no_hard,outlines,Github_easy---o10011.json,4,2,2,2,2,4,0,completed,,,0.848682,0.0824373,0.0376042,0.0447285,3864,587,156.25,41,44,2,2,0,0,0,0,0,1,1,0,true,false,false,false,true,false,false,false,true,false,false,false,false,true,false,false,false,false,true,false,false,false,false,false,false,false,false,false,false,false,false,true,false,false,false,true,false,false,true,true,false,false,false,24,8,2,6,2,4,0,false,false,false,false
Github_global_no_hard,outlines,Github_easy---o10012.json,4,1,3,1,3,4,0,completed,,,3.78717,0.0297808,0.013399,0.0163352,4104,386,96.5,19.75,25,1,2,1,0,0.333333,0,0,1,0.75,0.333333,true,false,false,false,true,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,true,false,false,false,false,true,false,false,false,false,false,true,false,false,true,false,false,false,true,false,false,false,12,2,0,2,0,0,2,false,false,false,false
Github_global_no_hard,outlines,Github_easy---o10013.json,4,2,2,2,2,4,0,completed,,,5.39014,0.160213,0.0731837,0.0868233,4797,750,232,57.75,69,2,1,1,0,0.5,0,0,1,0.75,0.5,true,false,false,false,true,false,false,false,false,false,false,false,false,true,false,false,false,false,true,false,false,true,false,false,false,false,true,false,false,false,false,true,true,false,false,true,false,false,true,true,false,false,false,30,11,4,6,2,4,1,false,false,true,false
Github_global_no_hard,outlines,Github_easy---o10014.json,2,1,1,1,1,2,0,completed,,,0.660632,0.158199,0.071538,0.086493,2473,287,212,61,64,1,1,0,0,0,0,0,1,1,0,true,false,false,false,true,false,false,false,false,false,false,false,false,false,false,false,false,false,true,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,false,true,false,false,true,true,false,fa

Aperçu : 12 / 4072 lignes.

32 graphiques disponibles — cliquez sur les titres pour les ouvrir.

## 4. Features extraites et analyses raffinées V1/V2

Les aperçus des tables montrent les features réellement disponibles. Les galeries couvrent les familles numériques, objets/regex, combinateurs, `not` et les synthèses. Les graphiques existants sont lus dans les deux organisations de dossiers utilisées par les runs.

`REGENERATE_REFINED_V2=True` recalcule la V2 depuis les tables V1, sans refaire l'extraction initiale. Une absence de données est signalée, sans bloquer les autres frameworks.


In [5]:
UNDER_FIELDNAMES = [
    "context_family",
    "context_feature",
    "context_value",
    "support_invalid_tests",
    "support_schemas",
    "under_count",
    "under_rate_invalid_only",
    "baseline_under_rate_invalid_only",
    "under_lift_invalid_only",
    "low_support",
]

OVER_FIELDNAMES = [
    "context_family",
    "context_feature",
    "context_value",
    "support_valid_tests",
    "support_schemas",
    "over_count",
    "over_rate_valid_only",
    "baseline_over_rate_valid_only",
    "over_lift_valid_only",
    "low_support",
]


def generate_refined_v2(framework: str, dataset_choice: str | None = None) -> dict[str, Path | int]:
    """Génère les tables et les plots raffinés v2 pour un framework.

    Cette fonction appelle directement les fonctions du script v2 :
    conditional_under_risk, conditional_over_risk, schema_level_risk,
    write_plots, cooccurrence_heatmap, top_examples et write_report.
    """
    selected_dataset = resolve_dataset(framework, dataset_choice)
    source_dir = run_dir(framework, dataset_choice) / "refined_feature_analysis"
    output_data_dir = V2_OUTPUT_ROOT / framework / selected_dataset / "tables"
    output_plot_dir = V2_OUTPUT_ROOT / framework / selected_dataset / "plots"

    test_features = source_dir / "refined_test_features.csv"
    schema_features = source_dir / "refined_schema_features.csv"
    if not test_features.exists() or not schema_features.exists():
        raise FileNotFoundError(
            "Tables raffinées v1 absentes pour "
            f"{framework}/{selected_dataset}. Attendu : {source_dir}"
        )

    output_data_dir.mkdir(parents=True, exist_ok=True)
    output_plot_dir.mkdir(parents=True, exist_ok=True)

    test_rows = refined_v2.read_csv(test_features)
    schema_rows = refined_v2.read_csv(schema_features)

    under_rows = refined_v2.conditional_under_risk(test_rows)
    over_rows = refined_v2.conditional_over_risk(test_rows)
    schema_risk_rows = refined_v2.schema_level_risk(schema_rows, test_rows)

    refined_v2.write_csv(output_data_dir / "under_invalid_only_risk.csv", under_rows, UNDER_FIELDNAMES)
    refined_v2.write_csv(output_data_dir / "over_valid_only_risk.csv", over_rows, OVER_FIELDNAMES)
    refined_v2.write_csv(output_data_dir / "schema_level_context_risk.csv", schema_risk_rows)

    # Ici on génère les plots v2 depuis les tables, au lieu de lire des plots déjà existants.
    refined_v2.write_plots(output_plot_dir, test_rows, under_rows, over_rows)
    refined_v2.cooccurrence_heatmap(
        output_plot_dir / "summary" / "cooccurrence_under_schemas.svg",
        "Keyword co-occurrence in UNDER schemas",
        refined_v2.cooccurrence_rows(schema_rows, DATA_ROOT, "under"),
    )
    refined_v2.cooccurrence_heatmap(
        output_plot_dir / "summary" / "cooccurrence_over_schemas.svg",
        "Keyword co-occurrence in OVER schemas",
        refined_v2.cooccurrence_rows(schema_rows, DATA_ROOT, "over"),
    )

    examples = refined_v2.top_examples(test_rows, under_rows, over_rows, DATA_ROOT)
    refined_v2.write_csv(output_data_dir / "top_context_examples.csv", examples)
    refined_v2.write_report(output_data_dir / "refined_feature_analysis_v2_report.md", test_rows, under_rows, over_rows, schema_risk_rows)

    return {
        "framework": framework,
        "dataset": selected_dataset,
        "source_dir": source_dir,
        "output_data_dir": output_data_dir,
        "output_plot_dir": output_plot_dir,
        "n_test_rows": len(test_rows),
        "n_schema_rows": len(schema_rows),
    }


In [6]:
def show_refined(framework):
    display(Markdown(f"### Features — {framework} / {resolve_dataset(framework)}"))
    source = run_dir(framework)
    for name in ("refined_schema_features.csv", "refined_test_features.csv"):
        show_csv(source / "refined_feature_analysis" / name, limit=3)
    for version in ("refined_feature_analysis", "refined_feature_analysis_v2"):
        for directory in (source / version / "plots", source / "plots" / version):
            if directory.is_dir():
                display(Markdown(f"#### {version}"))
                show_gallery(directory)
    table_root = source / "refined_feature_analysis_v2"
    if REGENERATE_REFINED_V2:
        try:
            if str(SCRIPTS_DIR) not in sys.path:
                sys.path.insert(0, str(SCRIPTS_DIR))
            global refined_v2
            import analyze_refined_features_v2 as refined_v2
            info = generate_refined_v2(framework)
            table_root = Path(info["output_data_dir"])
            show_gallery(Path(info["output_plot_dir"]))
        except (FileNotFoundError, ImportError) as exc:
            display(Markdown(f"V2 non régénérée : {exc}"))
    for name in ("under_invalid_only_risk.csv", "over_valid_only_risk.csv", "schema_level_context_risk.csv", "top_context_examples.csv"):
        show_csv(table_root / name)
    for target in TARGETS:
        features = MODELS_ROOT / framework / "modeling" / f"selected_{target}_features.txt"
        if features.is_file():
            values = features.read_text().splitlines()
            show_rows([{"feature retenue": x} for x in values if x], f"{target.upper()} — features retenues", limit=None)

for framework in FRAMEWORKS:
    show_refined(framework)


### Features — guidance / Github_global

**refined_schema_features.csv**

schema_id,has_under,has_over,under_test_count,over_test_count,correct_test_count,total_test_count,numeric_keyword_count,numeric_keywords_present,numeric_target_type,numeric_is_in_properties,numeric_property_required,numeric_has_default,numeric_has_min_and_max,numeric_parent_keyword,numeric_depth,patternProperties_occurrence_count,patternProperties_pattern_count,patternProperties_with_properties,patternProperties_has_additionalProperties,additionalProperties_value,patternProperties_regex_has_anchor,patternProperties_regex_has_dotstar,patternProperties_regex_has_alternation,patternProperties_regex_has_charclass,patternProperties_regex_complexity_score,not_count,not_depth_min,not_depth_max,not_depth_avg,not_parent_keyword,not_target_type,not_contains_enum,not_contains_const,not_contains_pattern,not_contains_properties,not_contains_required,not_contains_numeric,not_contains_anyOf,not_contains_allOf,not_contains_oneOf,not_sibling_keyword_count,allOf_count,anyOf_count,oneOf_count,combinator_count,combinator_type,combinator_depth_min,combinator_depth_max,combinator_depth_avg,combinator_branch_count_min,combinator_branch_count_max,combinator_branch_count_avg,branches_have_same_type,branches_conflicting_types,branches_have_required,branches_have_properties,branches_have_not,branches_have_enum,branches_have_const,branches_have_pattern,branches_have_numeric,branches_have_object_bounds,branches_overlapping_properties,object_context_count,object_parent_keyword,object_target_type,object_properties_count_max,object_required_count_max,object_additionalProperties_value,object_has_minProperties,object_has_maxProperties,object_has_min_and_max_properties,object_has_propertyNames,object_required_subset_of_properties,object_depth_max,enum_context_count,enum_target_type,enum_parent_keyword,enum_size_max,enum_contains_null,enum_contains_mixed_types,const_context_count,const_target_type,const_parent_keyword,const_type,string_context_count,string_parent_keyword,string_target_type,string_has_pattern,string_has_minLength,string_has_maxLength,string_has_min_and_max_length,string_has_format,string_format_value,string_pattern_complexity_score,array_context_count,array_parent_keyword,array_target_type,array_items_kind,array_prefixItems_count_max,array_has_minItems,array_has_maxItems,array_has_min_and_max_items,array_has_uniqueItems,array_has_contains,array_has_minContains,array_has_maxContains,complex_keywords_same_node_max,complex_keywords_same_node_avg,local_cooccurrence_pairs,has_minimum,has_maximum,has_exclusiveMinimum,has_exclusiveMaximum,has_multipleOf,has_patternProperties,has_not,has_allOf,has_anyOf,has_oneOf,same_node_not_and_enum,same_node_not_and_type,same_node_not_and_pattern,same_node_allOf_and_not,same_node_allOf_and_required,same_node_allOf_and_properties,same_node_oneOf_and_required,same_node_not_and_properties,same_node_not_and_required,same_node_patternProperties_and_additionalProperties,same_node_properties_and_patternProperties,same_node_properties_and_required,same_node_properties_and_additionalProperties,same_node_minProperties_and_required,same_node_combinator_and_patternProperties,same_node_combinator_and_numeric,same_node_combinator_and_required,same_node_combinator_and_properties,instance_matching_pattern_keys_count_bucket,object_properties_count_bucket,object_required_count_bucket,object_missing_required_count_bucket,object_extra_properties_count_bucket,enum_size_bucket,array_prefixItems_count_bucket,array_invalid_items_count_bucket,not_sibling_keyword_count_bucket,combinator_branch_count_bucket,allOf_satisfied_branch_count_bucket,allOf_satisfied_branch_ratio_bucket,anyOf_satisfied_branch_count_bucket,anyOf_satisfied_branch_ratio_bucket,oneOf_satisfied_branch_count_bucket,oneOf_satisfied_branch_ratio_bucket
Github_easy---o10008.json,false,false,0,0,3,3,0,,absent,false,false,false,false,absent,0,0,0,false,false,absent,false,false,false,false,0,0,0,0,0,absent,absent,false,false,false,false,false,false,false,false,false,0,0,0,0,0,abse

Aperçu : 3 / 4960 lignes.

**refined_test_features.csv**

...

Aperçu : 12 / 118 lignes.

**UNDER — features retenues**

feature retenue
instance_string_total_length
instance_string_max_length
schema_keyword_count
complex_keywords_same_node_avg
logical_complex_keywords_same_node_count
object_complex_keywords_same_node_count
regex_complex_keywords_same_node_count
instance_total_object_properties_recursive
numeric_boundary_case
instance_string_count


**OVER — features retenues**

feature retenue
instance_has_unmatched_keys
unmatched_keys_allowed_by_additionalProperties
instance_num_properties
unmatched_key_count_when_additionalProperties_true
additionalProperties_mode
branches_have_same_type
combinator_type
combinator_branch_count_max
patternProperties_anchor_mix
combinator_count


## 5. Meilleurs modèles GitHub : résultats enregistrés

Les scores du réentraînement final et les matrices de confusion sont affichés sur la partition **test** uniquement. Guidance UNDER n'a pas de modèle : aucun exemple positif dans les données d'entraînement correspondantes.

La validation croisée sauvegardée utilise encore d'anciennes listes de features ; elle est présentée séparément et ne doit pas être attribuée automatiquement aux modèles finaux.


In [7]:
show_rows([r for r in read_rows(COVERAGE_ROOT / "filtered_retraining_summary.csv") if r["framework"] in FRAMEWORKS], "Configuration retenue")
show_rows([r for r in read_rows(COVERAGE_ROOT / "retained_list_retraining_scores.csv") if r["framework"] in FRAMEWORKS], "Scores finaux enregistrés")
for framework in FRAMEWORKS:
    display(Markdown(f"### {framework}"))
    for target in TARGETS:
        metrics_dir = MODELS_ROOT / framework / "metrics"
        rows = [r for r in read_rows(metrics_dir / f"{target}_metrics.csv") if r.get("split") == "test"]
        show_rows(rows, f"{target.upper()} — test enregistré")
        matrices = [r for r in read_rows(metrics_dir / f"{target}_confusion_matrix.csv") if r.get("split") == "test"]
        show_confusions(matrices, f"{framework} {target.upper()}")
    show_gallery(MODELS_ROOT / framework / "plots" / "feature_importance")
show_rows([r for r in read_rows(COVERAGE_ROOT / "cross_validation_summary.csv") if r["framework"] in FRAMEWORKS], "Validation croisée historique — vérifier le nombre de features")


**Configuration retenue**

framework,target,status,rows,positives,retained_features,selected_model
guidance,under,single_class,15208,0,0,
guidance,over,trained,6349,3315,117,random_forest_leaf2_0.7
outlines,under,trained,9787,1242,146,lightgbm_lr0.05_leaves31
outlines,over,trained,5267,831,65,random_forest_leaf5_sqrt
xgr,under,trained,14046,2159,161,random_forest_leaf2_sqrt
xgr,over,trained,7485,1424,117,random_forest_leaf2_0.7


**Scores finaux enregistrés**

framework,target,model,threshold,n,positives,negatives,accuracy,precision,recall,f1,roc_auc,pr_auc,balanced_accuracy
guidance,over,random_forest_leaf2_0.7,0.32,958,523,435,0.73382,0.708723,0.869981,0.781116,0.835503,0.862841,0.720048
outlines,under,lightgbm_lr0.05_leaves31,0.87,1436,170,1266,0.96727,0.962406,0.752941,0.844884,0.985403,0.943081,0.874496
outlines,over,random_forest_leaf5_sqrt,0.72,823,125,698,0.947752,0.894231,0.744,0.812227,0.899977,0.842879,0.86412
xgr,under,random_forest_leaf2_sqrt,0.44,2089,312,1777,0.920057,0.71261,0.778846,0.744257,0.953533,0.831617,0.861849
xgr,over,random_forest_leaf2_0.7,0.44,1146,222,924,0.903141,0.778894,0.698198,0.736342,0.931996,0.814236,0.82529


### guidance

...

**outlines OVER — random_forest_leaf5_sqrt test**

Vérité / Prédiction,Négatif,Positif
Négatif (pas d'erreur),687,11
Positif (UNDER ou OVER),32,93


4 graphiques disponibles — cliquez sur les titres pour les ouvrir.

**Validation croisée historique — vérifier le nombre de features**

framework,target,model,status,folds,rows,positives,negatives,features,tp_sum,fn_sum,fp_sum,tn_sum,accuracy_mean,accuracy_std,accuracy_min,accuracy_max,precision_mean,precision_std,precision_min,precision_max,recall_mean,recall_std,recall_min,recall_max,f1_mean,f1_std,f1_min,f1_max,roc_auc_mean,roc_auc_std,roc_auc_min,roc_auc_max,pr_auc_mean,pr_auc_std,pr_auc_min,pr_auc_max,balanced_accuracy_mean,balanced_accuracy_std,balanced_accuracy_min,balanced_accuracy_max
guidance,over,random_forest_leaf2_0.7,ok,5,6349,3315,3034,138,2784,531,1058,1976,0.749725,0.0146965,0.729134,0.766142,0.728265,0.0388843,0.69409,0.771212,0.839819,0.0590397,0.767722,0.903469,0.777764,0.00907717,0.767568,0.787879,0.839976,0.0117552,0.821422,0.853595,0.858133,0.0084719,0.846989,0.868024,0.745545,0.0173246,0.723249,0.765095
outlines,under,lightgbm_lr0.05_leaves31,ok,5,9787,1242,8545,167,989,253,197,8348,0.954019,0.00950355,0.939704,0.962717,0.843938,0.0864666,0.724739,0.939698,0.796365,0.0343455,0.751004,0.842105,0.816001,0.0249668,0.779026,0.842333,0.96232,0.00519089,0.954617,0.969006,0.899716,0.00530363,0.892569,0.904644,0.886657,0.00979648,0.871991,0.897953
outlines,over,random_forest_leaf5_sqrt,ok,5,5267,831,4436,81,573,258,130,4306,0.926337,0.012028,0.914611,0.941176,0.837706,0.115315,0.701571,0.972973,0.689582,0.102943,0.554217,0.807229,0.745634,0.041814,0.69697,0.793846,0.881601,0.0343763,0.826271,0.914503,0.799701,0.0433346,0.741781,0.836017,0.830143,0.0418633,0.773726,0.871624
xgr,under,random_forest_leaf2_sqrt,ok,5,14046,2159,11887,185,1623,536,478,11409,0.927809,0.00713961,0.917764,0.936185,0.77816,0.0582911,0.725225,0.847645,0.751802,0.0497384,0.698851,0.819026,0.762062,0.0166895,0.736,0.779249,0.954516,0.00458523,0.949549,0.961654,0.841609,0.0248613,0.809944,0.87294,0.855796,0.0190501,0.836815,0.883861
xgr,over,random_forest_leaf2_0.7,ok,5,7485,1424,6061,139,972,452,150,5911,0.919575,0.00776554,0.910488,0.927807,0.873581,0.0575168,0.83004,0.968944,0.682604,0.0812418,0.547368,0.747368,0.761444,0.0395601,0.699552,0.793296,0.948041,0.00722964,0.939805,0.957016,0.868532,0.0214218,0.838851,0.892173,0.828929,0.0350605,0.771622,0.857582


### Réexécuter les modèles retenus

Les cellules suivantes chargent les pickles et exécutent `predict_proba`, sans entraînement ni modification des artefacts. Elles utilisent par défaut le Python de `.venv` pour disposer des bibliothèques des modèles, indépendamment du noyau Jupyter.

Pour XGR, `models_recovered/` est privilégié de façon cohérente. Une bibliothèque manquante ou une version scikit-learn incompatible est signalée comme erreur de calcul ; les scores enregistrés restent lisibles. Aucun score historique n'est présenté comme un recalcul réussi.


In [8]:
MODEL_WORKER = 'import csv, json, math, sys, warnings\nfrom pathlib import Path\nimport joblib\nimport numpy as np\nfrom sklearn.exceptions import InconsistentVersionWarning\nfrom sklearn.metrics import accuracy_score, precision_score, recall_score, f1_score, confusion_matrix, roc_auc_score, average_precision_score, balanced_accuracy_score\nwarnings.filterwarnings("error", category=InconsistentVersionWarning)\nconfig = json.loads(sys.argv[1])\nroot = Path(config["coverage_root"])\nresults = []\nfor framework in config["frameworks"]:\n    for target in config["targets"]:\n        result = {"framework": framework, "target": target, "mode": config["mode"]}\n        if framework == "guidance" and target == "under":\n            result.update(status="skipped", reason="Aucun modèle Guidance UNDER : absence de cas positifs à l\'apprentissage.")\n            results.append(result)\n            continue\n        try:\n            framework_root = root / "modeles_predictifs" / framework\n            # Use the retained recovered model consistently for XGR, rather than mixing versions.\n            recovered = framework_root / "models_recovered" / f"{target}_model.pkl"\n            path = recovered if recovered.is_file() and recovered.stat().st_size else framework_root / "models" / f"{target}_model.pkl"\n            result["model_path"] = str(path)\n            model = joblib.load(path)\n            features = model["selected_features"]\n            result.update(model=model["model_name"], threshold=float(model["threshold"]), features=len(features))\n            data_path = (framework_root / "modeling" / f"{target}_dataset.csv" if config["mode"] == "test"\n                         else root / "external_eval" / config["dataset"] / framework / f"{config[\'dataset\']}_external_features.csv")\n            with data_path.open(encoding="utf-8-sig", newline="") as handle:\n                rows = list(csv.DictReader(handle))\n            if config["mode"] == "test":\n                ids = set(map(str, model["split_schema_ids"]["test"]))\n                rows = [r for r in rows if r["schema_id"] in ids]\n            else:\n                negative = "CORRECT_INVALID" if target == "under" else "CORRECT_VALID"\n                rows = [r for r in rows if r.get("actual_result") in {"passed", "failed"}\n                        and r.get("failure_type") in {target.upper(), negative}]\n            if not rows:\n                result.update(status="skipped", reason="Aucun test disponible pour ce périmètre.")\n                results.append(result)\n                continue\n            missing = sorted(set(features) - set(rows[0]))\n            if missing:\n                raise ValueError(f"Features absentes du CSV : {missing}")\n            # The fitted preprocessor stores exact categorical column indices.\n            preprocessor = model["pipeline"].steps[0][1]\n            categorical = set()\n            for name, transformer, columns in preprocessor.transformers:\n                if name == "categorical":\n                    categorical.update(columns)\n            def numeric(value):\n                text = str(value).strip().lower()\n                if text == "true": return 1.0\n                if text == "false" or not text: return 0.0\n                try: number = float(text)\n                except ValueError: return 0.0\n                return number if math.isfinite(number) else 0.0\n            matrix = np.asarray([[str(row.get(f, "")) or "absent" if i in categorical else numeric(row.get(f, 0))\n                                  for i, f in enumerate(features)] for row in rows], dtype=object)\n            y = np.asarray([int(r[f"y_{target}"]) if config["mode"] == "test" else int(r["failure_type"] == target.upper()) for r in rows])\n            probabilities = model["pipeline"].predict_proba(matrix)[:, 1]\n            predicted = (probabilities >= model["threshold"]).astype(int)\n            tn, fp, fn, tp = confusion_matrix(y, predicted, labels=[0, 1]).ravel()\n            both_classes = len(set(y)) == 2\n            result.update(status="ok", n=len(rows), positives=int(y.sum()),\n                          accuracy=float(accuracy_score(y, predicted)), precision=float(precision_score(y, predicted, zero_division=0)),\n                          recall=float(recall_score(y, predicted, zero_division=0)), f1=float(f1_score(y, predicted, zero_division=0)),\n                          pr_auc=float(average_precision_score(y, probabilities)) if both_classes else None,\n                          roc_auc=float(roc_auc_score(y, probabilities)) if both_classes else None,\n                          balanced_accuracy=float(balanced_accuracy_score(y, predicted)) if both_classes else None,\n                          tn=int(tn), fp=int(fp), fn=int(fn), tp=int(tp))\n            if not both_classes:\n                result["note"] = "Une seule classe observée : AUC non définies ; la détection des positifs ne peut pas être évaluée sans positifs."\n        except Exception as exc:\n            result.update(status="error", reason=f"{type(exc).__name__}: {exc}")\n        results.append(result)\nprint(json.dumps(results, allow_nan=False))'

PREDICTION_RESULTS = {}
def run_predictions(mode):
    config = {"coverage_root": str(COVERAGE_ROOT), "frameworks": FRAMEWORKS, "targets": TARGETS,
              "dataset": EXTERNAL_DATASET, "mode": mode}
    result = subprocess.run([MODEL_PYTHON, "-c", MODEL_WORKER, json.dumps(config)],
                            cwd=REPO_ROOT, capture_output=True, text=True, timeout=300)
    if result.returncode:
        raise RuntimeError(result.stderr[-4000:] or result.stdout[-4000:])
    rows = json.loads(result.stdout)
    PREDICTION_RESULTS[mode] = rows
    score_columns = ["framework", "target", "status", "model", "threshold", "features", "n", "positives",
                     "accuracy", "precision", "recall", "f1", "pr_auc", "roc_auc", "balanced_accuracy", "reason", "note"]
    show_rows([{k: row[k] for k in score_columns if k in row} for row in rows], f"Prédictions recalculées — {mode}", limit=None)
    for row in rows:
        if row["status"] == "ok":
            display(Markdown(f"Modèle chargé : `{row['model_path']}`"))
            show_confusions([row], f"{row['framework']} {row['target'].upper()} — {mode}")
    return rows

if RUN_MODEL_PREDICTIONS:
    recalculated_test = run_predictions("test")
else:
    display(Markdown("Recalcul désactivé ; scores enregistrés affichés ci-dessus."))


**Prédictions recalculées — test**

framework,target,status,reason,model,threshold,features,n,positives,accuracy,precision,recall,f1,pr_auc,roc_auc,balanced_accuracy
guidance,under,skipped,Aucun modèle Guidance UNDER : absence de cas positifs à l'apprentissage.,,,,,,,,,,,,
guidance,over,ok,,random_forest_leaf2_0.7,0.31999999999999995,117,958,523,0.7338204592901879,0.7087227414330218,0.869980879541109,0.7811158798283262,0.8628449233278539,0.8355025164282104,0.7200479110349223
xgr,under,ok,,random_forest_leaf2_sqrt,0.43999999999999995,161,2089,312,0.9200574437529918,0.7126099706744868,0.7788461538461539,0.7442572741194488,0.831616870636166,0.9535328557205316,0.8618485130513831
xgr,over,ok,,random_forest_leaf2_0.7,0.43999999999999995,117,1146,222,0.9031413612565445,0.7788944723618091,0.6981981981981982,0.7363420427553444,0.8142364641589985,0.9319961194961195,0.8252895752895753
outlines,under,ok,,lightgbm_lr0.05_leaves31,0.8699999999999999,146,1436,170,0.9672701949860725,0.9624060150375939,0.7529411764705882,0.8448844884488449,0.9430812277909725,0.9854033082427284,0.8744958646965895
outlines,over,ok,,random_forest_leaf5_sqrt,0.72,65,823,125,0.9477521263669502,0.8942307692307693,0.744,0.8122270742358079,0.8428792723219032,0.8999770773638969,0.8641203438395415


Modèle chargé : `extension_jsonschemabench\coverage_prediction\modeles_predictifs\guidance\models\over_model.pkl`

**guidance OVER — test — random_forest_leaf2_0.7 **

Vérité / Prédiction,Négatif,Positif
Négatif (pas d'erreur),248,187
Positif (UNDER ou OVER),68,455


...

**outlines UNDER — test — lightgbm_lr0.05_leaves31 **

Vérité / Prédiction,Négatif,Positif
Négatif (pas d'erreur),1261,5
Positif (UNDER ou OVER),42,128


Modèle chargé : `extension_jsonschemabench\coverage_prediction\modeles_predictifs\outlines\models\over_model.pkl`

**outlines OVER — test — random_forest_leaf5_sqrt **

Vérité / Prédiction,Négatif,Positif
Négatif (pas d'erreur),687,11
Positif (UNDER ou OVER),32,93


## 6. Arbres de décision et règles déduites

Pour chaque framework et cible : arbre graphique, scores de l'arbre explicatif et **liste complète des règles positives**, avec le rapport rédigé. Ces modèles explicatifs ne sont pas les Random Forest/boosting évalués dans la section précédente. Guidance UNDER n'a pas d'arbre exploitable.


In [9]:
show_csv(COVERAGE_ROOT / "rules" / "decision_tree_rule_summary.csv", limit=None)
for framework in FRAMEWORKS:
    for target in TARGETS:
        directory = COVERAGE_ROOT / "rules" / framework / target
        display(Markdown(f"### Règles — {framework} {target.upper()}"))
        if not directory.is_dir():
            display(Markdown("Aucun arbre enregistré pour cette cible."))
            continue
        show_gallery(directory, recursive=False)
        show_csv(directory / f"{target}_selected_metrics.csv", limit=None)
        show_csv(directory / f"{target}_positive_rules.csv", limit=None)
        show_report(directory / f"{target}_rules.md")


**decision_tree_rule_summary.csv**

framework,target,model,features,split,dataset,threshold,n,positives,negatives,accuracy,precision,recall,f1,roc_auc,pr_auc,balanced_accuracy,tn,fp,fn,tp
guidance,over,tree_depth5_leaf50,117,test,all,0.29,965,555,410,0.746114,0.746032,0.846847,0.793249,0.808367,0.838457,0.728301,250,160,85,470
outlines,under,tree_depth5_leaf50,146,test,all,0.86,1405,143,1262,0.954448,0.907216,0.615385,0.733333,0.915042,0.710649,0.804127,1253,9,55,88
outlines,over,tree_depth5_leaf50,65,test,all,0.78,785,133,652,0.936306,0.867257,0.736842,0.796748,0.927568,0.851046,0.856918,637,15,35,98
xgr,under,tree_depth5_leaf20,161,test,all,0.74,2185,335,1850,0.815561,0.449555,0.904478,0.600595,0.867957,0.448171,0.851969,1479,371,32,303
xgr,over,tree_depth5_leaf20,117,test,all,0.7,1151,204,947,0.923545,0.89726,0.642157,0.748571,0.880024,0.761925,0.813159,932,15,73,131


### Règles — guidance UNDER

Aucun arbre enregistré pour cette cible.

### Règles — guidance OVER

...

**over_selected_metrics.csv**

model,split,dataset,threshold,n,positives,negatives,accuracy,precision,recall,f1,roc_auc,pr_auc,balanced_accuracy,tn,fp,fn,tp
tree_depth5_leaf50,test,all,0.78,785,133,652,0.936306,0.867257,0.736842,0.796748,0.927568,0.851046,0.856918,637,15,35,98


**over_positive_rules.csv**

target,leaf_id,predicted_class,positive_rate_train_leaf,positive_count_train_leaf_weighted,negative_count_train_leaf_weighted,weighted_support_train_leaf,n_conditions,test_support,test_positives,test_precision,test_recall_contribution,rule
over,25,OVER,1,300.816,0,300.816,3,18,18,1,0.135338,unmatched_keys_allowed_by_additionalProperties > 0.5 AND branches_have_properties <= 0.5 AND instance_num_properties > 8.5
over,23,OVER,1,172.809,0,172.809,5,16,16,1,0.120301,unmatched_keys_allowed_by_additionalProperties > 0.5 AND branches_have_properties <= 0.5 AND instance_num_properties <= 8.5 AND instance_num_properties <= 4.5 AND unmatched_keys_allowed_by_additionalProperties > 1.5
over,22,OVER,0.996871,188.81,0.592587,189.403,5,8,8,1,0.0601504,unmatched_keys_allowed_by_additionalProperties > 0.5 AND branches_have_properties <= 0.5 AND instance_num_properties <= 8.5 AND instance_num_properties <= 4.5 AND unmatched_keys_allowed_by_additionalProperties <= 1.5
over,24,OVER,0.991653,211.211,1.77776,212.989,4,9,9,1,0.0676692,unmatched_keys_allowed_by_additionalProperties > 0.5 AND branches_have_properties <= 0.5 AND instance_num_properties <= 8.5 AND instance_num_properties > 4.5
over,26,OVER,0.912915,105.606,10.074,115.68,2,11,10,0.909091,0.075188,unmatched_keys_allowed_by_additionalProperties > 0.5 AND branches_have_properties > 0.5
over,17,OVER,0.885252,128.007,16.5924,144.599,3,17,17,1,0.12782,unmatched_keys_allowed_by_additionalProperties <= 0.5 AND combinator_same_type_ratio > 0.416667 AND has_allOf > 0.5
over,6,OVER,0.848176,96.0052,17.185,113.19,5,15,10,0.666667,0.075188,unmatched_keys_allowed_by_additionalProperties <= 0.5 AND combinator_same_type_ratio <= 0.416667 AND has_patternProperties <= 0.5 AND instance_num_properties <= 0.5 AND additionalProperties_mode_false > 0.5
over,10,OVER,0.822909,118.406,25.4812,143.888,3,19,10,0.526316,0.075188,unmatched_keys_allowed_by_additionalProperties <= 0.5 AND combinator_same_type_ratio <= 0.416667 AND has_patternProperties > 0.5


# Outlines — interprétation des règles de prédiction OVER

Ce document réorganise les règles extraites de l’arbre de décision entraîné pour prédire les cas **OVER** du framework **Outlines**.

Sources utilisées :

- `over_rules.md` : règles, métriques et arbre textuel ;
- `over_tree.svg` : représentation graphique de l’arbre ;
- `analyze_refined_features.py` : définition des features utilisées.

![Arbre de décision Outlines OVER](outlines_over_tree.svg)

---

## 1. Signification d’un cas OVER

Un cas **OVER** correspond à la situation suivante :

```text
instance attendue valide + instance rejetée par Outlines
```

Outlines applique alors une contrainte plus restrictive que le JSON Schema de référence et rejette une instance qui devrait être acceptée.

---

## 2. Performances de l’arbre retenu

| Élément | Valeur |
|---|---:|
| Arbre | `tree_depth5_leaf50` |
| Seuil de décision | `0.78` |
| F1 test | `0.796748` |
| Précision test | `0.867257` |
| Recall test | `0.736842` |
| PR-AUC test | `0.851046` |
| ROC-AUC test | `0.927568` |

L’arbre a été entraîné avec un découpage par `schema_id`. Les schémas du jeu de test ne sont donc pas présents dans le jeu d’entraînement.

---

## 3. Comment lire les métriques d’une règle

Chaque règle correspond à une feuille de l’arbre.

- **Taux positif feuille train** : proportion de cas OVER parmi les exemples d’entraînement arrivant dans cette feuille.
- **Support test** : nombre de tests du jeu de test satisfaisant la règle.
- **Précision test** : proportion de vrais cas OVER parmi les tests couverts.
- **Contribution au recall test** : proportion de tous les vrais cas OVER du jeu de test capturée par la règle.

### Relation entre `class: 1` et le seuil final

L’arbre textuel affiche la classe obtenue avec le seuil standard de `0.5`. Le modèle final utilise toutefois un seuil plus strict :

```text
0.78
```

Une feuille peut donc être affichée comme `class: 1` dans l’arbre textuel sans être exportée comme règle positive finale si sa probabilité de cas OVER reste inférieure ou égale à `0.78`.

Les huit règles documentées ici sont les feuilles qui dépassent effectivement le seuil final.

---

## 4. Rappel rapide des features utilisées

- `unmatched_keys_allowed_by_additionalProperties` : nombre cumulé de clés de l’instance qui ne correspondent ni à `properties` ni à `patternProperties`, mais qui ne sont pas immédiatement interdites par `additionalProperties: false`.
- `branches_have_properties` : booléen indiquant si au moins une branche d’un `allOf`, `anyOf` ou `oneOf` contient un mot-clé `properties`.
- `instance_num_properties` : nombre de propriétés de l’objet situé à la racine de l’instance ; la valeur est `0` si la racine n’est pas un objet.
- `combinator_same_type_ratio` : proportion des occurrences de combinateurs dont les branches déclarant explicitement un type sont considérées comme homogènes.
- `has_allOf` : booléen indiquant que le schéma contient au moins une occurrence de `allOf`.
- `has_patternProperties` : booléen indiquant que le schéma contient au moins un mot-clé `patternProperties`.
- `additionalProperties_mode_false` : indicateur issu de l’encodage catégoriel, actif lorsque le mode global détecté pour `additionalProperties` est `false`.

### Signification de « cumulé »

Le calcul descend dans les objets et sous-schémas visités. Une même instance peut être évaluée dans plusieurs branches de combinateurs ; le compteur représente donc les occurrences observées pendant cette évaluation, et pas nécessairement uniquement les chemins de clés distincts.

---

## 5. Résumé opérationnel de l’arbre

Avec le seuil final de `0.78`, les huit feuilles positives peuvent être regroupées en trois grands profils :

```text
Outlines prédit OVER si :

PROFIL A
unmatched_keys_allowed_by_additionalProperties >= 1

OU

PROFIL B
unmatched_keys_allowed_by_additionalProperties = 0
ET combinator_same_type_ratio > 0.416667
ET has_allOf = true

OU

PROFIL C
unmatched_keys_allowed_by_additionalProperties = 0
ET combinator_same_type_ratio <= 0.416667
ET (
     has_patternProperties = true

     OU

     has_patternProperties = false
     ET instance_num_properties = 0
     ET additionalProperties_mode_false = true
)
```

Les subdivisions du profil A sur le nombre de propriétés racines, le nombre de clés non reconnues et la présence de `properties` dans les branches ne changent pas la prédiction finale : elles servent surtout à estimer des probabilités légèrement différentes.

---

## 6. Vue synthétique des profils

Les métriques agrégées sont approximatives, car elles sont reconstruites à partir des métriques de feuilles arrondies.

| Profil | Règles regroupées | Support test | Précision agrégée approximative | Contribution au recall |
|---|---|---:|---:|---:|
| Au moins une clé non reconnue et non immédiatement interdite | 1, 3, 4, 5, 6 | 62 | ≈ 0.984 | 0.458 |
| Aucun unmatched, combinateurs plutôt homogènes et présence de `allOf` | 2 | 17 | 1.000 | 0.128 |
| Aucun unmatched, faible homogénéité et `patternProperties` | 8 | 19 | 0.526 | 0.075 |
| Aucun unmatched, faible homogénéité, pas de `patternProperties`, instance racine vide et objet fermé | 7 | 15 | 0.667 | 0.075 |

Les quatre lignes couvrent ensemble environ :

```text
0.458 + 0.128 + 0.075 + 0.075 = 0.736
```

du recall test, ce qui correspond au recall global de l’arbre à l’arrondi près.

---

# 7. Profil A — clés non reconnues mais non immédiatement interdites

## Règle générale

```text
unmatched_keys_allowed_by_additionalProperties >= 1
```

Règles concernées : **1, 3, 4, 5 et 6**.

Toutes les feuilles situées sous cette branche dépassent le seuil `0.78`, que :

- des branches de combinateurs contiennent ou non `properties` ;
- l’instance racine contienne peu ou beaucoup de propriétés ;
- une ou plusieurs clés soient comptées comme non reconnues.

## Interprétation

Ce profil correspond à des instances contenant au moins une clé qui :

1. n’est pas nommée dans `properties` ;
2. ne correspond pas à un motif de `patternProperties` ;
3. n’est pas immédiatement rejetée par `additionalProperties: false`.

Dans les données de test, cette situation est fortement associée aux cas où Outlines rejette une instance pourtant valide. Le signal peut notamment apparaître dans les schémas ouverts, les schémas où `additionalProperties` est absent ou égal à `true`, ou lorsque les propriétés supplémentaires doivent être validées par un sous-schéma.

## Sous-profils de confiance

| Sous-profil | Règles | Support | Précision |
|---|---|---:|---:|
| Aucune branche de combinateur avec `properties`, instance avec au moins 9 propriétés racines | 1 | 18 | 1.000 |
| Aucune branche avec `properties`, instance avec 5 à 8 propriétés racines | 4 | 9 | 1.000 |
| Aucune branche avec `properties`, instance avec au plus 4 propriétés et au moins 2 unmatched | 3 | 16 | 1.000 |
| Aucune branche avec `properties`, instance avec au plus 4 propriétés et exactement 1 unmatched | 5 | 8 | 1.000 |
| Au moins une branche de combinateur contient `properties` | 6 | 11 | 0.909 |

Ces subdivisions modifient principalement le niveau de confiance. Elles ne changent pas la prédiction OVER dans cet arbre.

### Exemple réel à insérer

- `schema_id` : `[À REMPLIR]`
- `test_id` : `[À REMPLIR]`
- Clé ou chemin non reconnu : `[À REMPLIR]`
- Mode réel de `additionalProperties` : `[À REMPLIR]`
- Résultat du validateur de référence : valide
- Résultat Outlines : rejetée

**Requête de recherche à transmettre à l’outil :**

```text
Dans refined_test_features du run Outlines, cherche un test avec
failure_type == "OVER"
et unmatched_keys_allowed_by_additionalProperties >= 1.

Retourne :
- schema_id, test_id et test_index ;
- le JSON Schema complet ;
- l’instance complète ;
- la valeur exacte de unmatched_keys_allowed_by_additionalProperties ;
- instance_num_properties ;
- branches_have_properties ;
- additionalProperties_mode et additionalProperties_value ;
- les clés ou chemins qui ne correspondent ni à properties ni à
  patternProperties ;
- expected_validity et le résultat Outlines.

Vérifie avec le validateur de référence que l’instance est valide. Détermine
ensuite si chaque clé supplémentaire est autorisée parce que
additionalProperties est absent, égal à true, ou défini comme sous-schéma.
Si un sous-schéma est utilisé, vérifie que la valeur de la clé le respecte.
Ne modifie ni le schéma ni l’instance et n’invente aucune clé.
```

---

# 8. Profil B — `allOf` et combinateurs plutôt homogènes

## Règle

```text
unmatched_keys_allowed_by_additionalProperties = 0
AND combinator_same_type_ratio > 0.416667
AND has_allOf = true
```

Règle concernée : **2**.

## Interprétation

Aucune clé supplémentaire non reconnue n’est détectée. Le profil repose plutôt sur la structure logique du schéma :

- le schéma contient au moins un `allOf` ;
- plus de 41,67 % des occurrences de combinateurs sont considérées comme homogènes selon les types explicitement déclarés dans leurs branches.

Cette règle couvre 17 tests et possède une précision test de `1.000`. Elle décrit donc un profil fort dans cet arbre, lié à l’interaction entre `allOf` et des branches de types similaires.

### Exemple réel à insérer

- `schema_id` : `[À REMPLIR]`
- `test_id` : `[À REMPLIR]`
- Occurrence de `allOf` concernée : `[À REMPLIR]`
- Types déclarés dans les branches : `[À REMPLIR]`

**Requête de recherche à transmettre à l’outil :**

```text
Dans refined_test_features du run Outlines, cherche un test avec
failure_type == "OVER",
unmatched_keys_allowed_by_additionalProperties == 0,
combinator_same_type_ratio > 0.416667
et has_allOf == true.

Retourne schema_id, test_id, le schéma complet, l’instance complète,
allOf_count, combinator_count, combinator_same_type_count,
combinator_same_type_ratio et la liste des branches de chaque allOf avec
leurs types explicites. Vérifie que l’instance est valide selon le validateur
de référence et précise quelle occurrence de allOf est satisfaite par
l’instance. Indique ensuite que l’association avec la règle est prédictive,
sans présenter l’homogénéité des types comme une cause démontrée.
```

---

# 9. Profil C — faible homogénéité des combinateurs

Condition commune :

```text
unmatched_keys_allowed_by_additionalProperties = 0
AND combinator_same_type_ratio <= 0.416667
```

Deux variantes positives apparaissent.

---

## 9.1 Variante C1 — présence de `patternProperties`

```text
has_patternProperties = true
```

Règle concernée : **8**.

### Interprétation

Le schéma utilise `patternProperties`, mais aucune clé n’est comptée comme unmatched. Les clés de l’instance sont donc soit nommées explicitement, soit reconnues par au moins une expression régulière.

La règle peut illustrer des cas où la gestion des noms de propriétés par regex interagit avec les combinateurs du schéma.

### Exemple réel à insérer

- `schema_id` : `[À REMPLIR]`
- `test_id` : `[À REMPLIR]`
- Patterns concernés : `[À REMPLIR]`
- Clés de l’instance correspondant aux patterns : `[À REMPLIR]`

**Requête de recherche à transmettre à l’outil :**

```text
Dans refined_test_features du run Outlines, cherche un test avec
failure_type == "OVER",
unmatched_keys_allowed_by_additionalProperties == 0,
combinator_same_type_ratio <= 0.416667
et has_patternProperties == true.

Retourne schema_id, test_id, le schéma complet, l’instance complète,
les dictionnaires patternProperties, les clés de l’instance et les patterns
auxquels elles correspondent, ainsi que les occurrences de allOf, anyOf et
oneOf. Vérifie avec le validateur de référence que l’instance est valide.
Choisis de préférence un cas où la correspondance entre clés et regex est
facile à expliquer dans un rapport.
```

---

## 9.2 Variante C2 — objet fermé et instance racine sans propriété

```text
has_patternProperties = false
AND instance_num_properties = 0
AND additionalProperties_mode_false = true
```

Règle concernée : **7**.

### Interprétation

Cette variante décrit un schéma sans `patternProperties`, dans lequel le mode global de `additionalProperties` est `false`, appliqué à une instance dont l’objet racine ne contient aucune propriété — ou à une instance non objet, puisque `instance_num_properties` vaut également zéro dans ce cas.

Le profil peut correspondre à une interaction entre un objet fermé et les branches de combinateurs. L’exemple réel devra préciser le type de l’instance et vérifier qu’aucune propriété obligatoire ne manque.

### Exemple réel à insérer

- `schema_id` : `[À REMPLIR]`
- `test_id` : `[À REMPLIR]`
- Type de l’instance racine : `[À REMPLIR]`
- Liste des propriétés obligatoires : `[À REMPLIR]`

**Requête de recherche à transmettre à l’outil :**

```text
Dans refined_test_features du run Outlines, cherche un test avec
failure_type == "OVER",
unmatched_keys_allowed_by_additionalProperties == 0,
combinator_same_type_ratio <= 0.416667,
has_patternProperties == false,
instance_num_properties == 0
et additionalProperties_mode_false == true.

Retourne schema_id, test_id, instance_type, le schéma complet, l’instance
complète, tous les blocs additionalProperties: false, les tableaux required
et les combinateurs. Vérifie que l’instance est valide selon le validateur
de référence. Si l’instance est {}, explique pourquoi l’objet vide est valide.
Si l’instance n’est pas un objet, indique explicitement que
instance_num_properties vaut zéro par convention d’extraction.
```

---

# 10. Tableau détaillé des huit feuilles

Les conditions ci-dessous sont simplifiées en supprimant les seuils redondants hérités du chemin de l’arbre.

| Règle | Condition simplifiée | Taux train | Support | Précision | Recall | Niveau |
|---:|---|---:|---:|---:|---:|---|
| 1 | unmatched ≥ 1 ; aucune branche de combinateur avec `properties` ; au moins 9 propriétés racines | 1.000 | 18 | 1.000 | 0.135 | Très élevé |
| 2 | unmatched = 0 ; ratio de combinateurs homogènes > 0,416667 ; présence de `allOf` | 0.885 | 17 | 1.000 | 0.128 | Très élevé |
| 3 | unmatched ≥ 2 ; aucune branche avec `properties` ; au plus 4 propriétés racines | 1.000 | 16 | 1.000 | 0.120 | Très élevé |
| 4 | unmatched ≥ 1 ; aucune branche avec `properties` ; entre 5 et 8 propriétés racines | 0.992 | 9 | 1.000 | 0.068 | Très élevé, support faible |
| 5 | unmatched = 1 ; aucune branche avec `properties` ; au plus 4 propriétés racines | 0.997 | 8 | 1.000 | 0.060 | Très élevé, support faible |
| 6 | unmatched ≥ 1 ; au moins une branche de combinateur avec `properties` | 0.913 | 11 | 0.909 | 0.075 | Élevé |
| 7 | unmatched = 0 ; ratio homogène ≤ 0,416667 ; pas de `patternProperties` ; aucune propriété racine ; mode `additionalProperties=false` | 0.848 | 15 | 0.667 | 0.075 | Modéré |
| 8 | unmatched = 0 ; ratio homogène ≤ 0,416667 ; présence de `patternProperties` | 0.823 | 19 | 0.526 | 0.075 | Exploratoire |

---

# 11. Interprétation globale

## 11.1 Le signal principal concerne les clés non reconnues

La racine de l’arbre teste :

```text
unmatched_keys_allowed_by_additionalProperties <= 0.5
```

Toutes les feuilles de la branche opposée, où au moins une clé est comptée, dépassent le seuil final. Ce profil couvre 62 tests avec une précision agrégée approximative de `0.984`.

Il s’agit donc du signal le plus fort et le plus fréquent de cet arbre.

## 11.2 En l’absence de clés unmatched, la structure logique devient déterminante

Lorsque le compteur vaut zéro, l’arbre se tourne vers :

- la proportion de combinateurs homogènes ;
- la présence de `allOf` ;
- la présence de `patternProperties` ;
- la fermeture des objets avec `additionalProperties: false`.

## 11.3 Les splits internes du profil A ajustent surtout la confiance

Sous la branche `unmatched >= 1`, les deux côtés de tous les splits restent positifs :

- présence ou absence de `properties` dans les branches ;
- petit ou grand objet racine ;
- une ou plusieurs clés unmatched.

Ces features ne sont donc pas nécessaires pour résumer la décision finale, mais elles permettent de distinguer les feuilles ayant une précision de `1.000` de celle ayant une précision de `0.909`.

## 11.4 Nature de l’interprétation

Les profils sont des associations prédictives. Ils ne démontrent pas que `additionalProperties`, `allOf` ou `patternProperties` constitue seul la cause technique du rejet.

Pour établir une cause, il faut examiner :

1. le schéma réel ;
2. l’instance valide rejetée ;
3. le sous-schéma ou le motif concerné ;
4. éventuellement une réduction HDD ou une mutation contrôlée.

---

# 12. Requête générale pour compléter tous les exemples

```text
Lis le README des règles Outlines OVER et la table refined_test_features du
même run. Pour chaque profil demandé, filtre d’abord failure_type == "OVER".
Vérifie ensuite que expected_validity indique une instance valide et
qu’Outlines l’a rejetée.

Retourne :
- schema_id ;
- test_id et test_index ;
- les valeurs exactes des features de la règle ;
- le JSON Schema complet ;
- l’instance complète ;
- le résultat du validateur de référence ;
- le résultat Outlines.

Pour les règles sur additionalProperties, identifie les clés concernées et
précise si elles sont autorisées par absence du mot-clé, par true ou par un
sous-schéma. Pour les règles sur les combinateurs, indique quelles branches
sont satisfaites. Pour patternProperties, indique les correspondances entre
clés et regex.

Choisis un exemple compréhensible et n’invente aucune donnée. Distingue
toujours les conditions prédictives de l’arbre de la cause technique réelle.
Si cette cause ne peut pas être établie à partir du seul exemple, écris
qu’elle reste à confirmer.
```


## 7. Évaluation externe — GitHub vers Kubernetes

Les modèles GitHub sont appliqués aux features Kubernetes **sans réentraînement**. Les résultats historiques ci-dessous proviennent du run sauvegardé. Le recalcul optionnel réutilise les features existantes et les modèles retenus actuels.

**XGR OVER :** le run historique utilise le seuil 0,58 dans `models/`, tandis que le modèle récupéré retenu utilise 0,44. Un écart avec le recalcul est donc attendu et ne doit pas être masqué. Sur Kubernetes, l'absence de positifs UNDER empêche d'évaluer leur détection ; les faux positifs restent observables.


In [10]:
external_root = COVERAGE_ROOT / "external_eval" / EXTERNAL_DATASET
historical_external = [r for r in read_rows(external_root / "external_eval_summary.csv") if r["framework"] in FRAMEWORKS and r["target"] in TARGETS]
show_rows(historical_external, "Évaluation externe enregistrée", limit=None)
for row in historical_external:
    show_confusions([row], f"{row['framework']} {row['target'].upper()} — externe enregistré")
for framework in FRAMEWORKS:
    for target in TARGETS:
        path = external_root / framework / f"{target}_external_misclassified_tests.csv"
        if path.exists():
            display(Markdown(f"#### Exemples d'erreurs externes — {framework} {target.upper()}"))
            show_csv(path, limit=5)
if RUN_EXTERNAL_PREDICTIONS:
    recalculated_external = run_predictions("external")


**Évaluation externe enregistrée**

framework,target,dataset,status,reason,n,positives,negatives,model,model_path,threshold,accuracy,precision,recall,f1,roc_auc,pr_auc,balanced_accuracy,tn,fp,fn,tp
guidance,under,Kubernetes,skipped,/home/berrais/stage/jsonschemabench/extension_jsonschemabench/coverage_prediction/modeles_predictifs/guidance/models/under_model.pkl: missing_or_empty; /home/berrais/stage/jsonschemabench/extension_jsonschemabench/coverage_prediction/modeles_predictifs/guidance/models_recovered/under_model.pkl: missing_or_empty,2908,0,2908,,,,,,,,,,,,,,
guidance,over,Kubernetes,evaluated,,1658,827,831,random_forest_leaf2_0.7,/home/berrais/stage/jsonschemabench/extension_jsonschemabench/coverage_prediction/modeles_predictifs/guidance/models/over_model.pkl,0.32,0.750905,0.706587,0.856106,0.774194,0.823893,0.811876,0.751158,537,294,119,708
xgr,under,Kubernetes,evaluated,,2908,0,2908,random_forest_leaf2_sqrt,/home/berrais/stage/jsonschemabench/extension_jsonschemabench/coverage_prediction/modeles_predictifs/xgr/models_recovered/under_model.pkl,0.44,0.998281,0,0,0,,,,2903,5,0,0
xgr,over,Kubernetes,evaluated,,1680,346,1334,random_forest_leaf2_0.7,/home/berrais/stage/jsonschemabench/extension_jsonschemabench/coverage_prediction/modeles_predictifs/xgr/models/over_model.pkl,0.58,0.841667,0.987805,0.234104,0.378505,0.843885,0.597467,0.616677,1333,1,265,81
outlines,under,Kubernetes,evaluated,,2853,0,2853,lightgbm_lr0.05_leaves31,/home/berrais/stage/jsonschemabench/extension_jsonschemabench/coverage_prediction/modeles_predictifs/outlines/models/under_model.pkl,0.87,1,0,0,0,,,,2853,0,0,0
outlines,over,Kubernetes,evaluated,,1632,207,1425,random_forest_leaf5_sqrt,/home/berrais/stage/jsonschemabench/extension_jsonschemabench/coverage_prediction/modeles_predictifs/outlines/models/over_model.pkl,0.72,0.920343,1,0.371981,0.542254,0.829152,0.571496,0.68599,1425,0,130,77


**guidance OVER — externe enregistré — random_forest_leaf2_0.7 **

Vérité / Prédiction,Négatif,Positif
Négatif (pas d'erreur),537,294
Positif (UNDER ou OVER),119,708


**xgr UNDER — externe enregistré — random_forest_leaf2_sqrt **

...

**outlines UNDER — external — lightgbm_lr0.05_leaves31 **

Vérité / Prédiction,Négatif,Positif
Négatif (pas d'erreur),2853,0
Positif (UNDER ou OVER),0,0


Modèle chargé : `extension_jsonschemabench\coverage_prediction\modeles_predictifs\outlines\models\over_model.pkl`

**outlines OVER — external — random_forest_leaf5_sqrt **

Vérité / Prédiction,Négatif,Positif
Négatif (pas d'erreur),1425,0
Positif (UNDER ou OVER),130,77


## 8. Expérience distincte : entraînement sur Kubernetes

Ces modèles sont appris sur une partie des schémas Kubernetes et testés sur une autre partie du même dataset. Ce ne sont pas les modèles GitHub de l'évaluation externe. Les tables de validation permettent de retrouver le candidat retenu ; seuls ses scores de test et sa matrice sont affichés. Aucun entraînement n'est lancé ici.


In [11]:
for framework in FRAMEWORKS:
    directory = COVERAGE_ROOT / "kubernetes_eval" / framework
    display(Markdown(f"### Entraînement Kubernetes — {framework}"))
    for target in TARGETS:
        candidates = read_rows(directory / "metrics" / f"{target}_model_selection.csv")
        if not candidates:
            display(Markdown(f"{target.upper()} : aucun candidat enregistré (UNDER n'a pas de positifs ici)."))
            continue
        best = max(candidates, key=lambda r: tuple(float(r[k]) for k in ("pr_auc", "f1", "recall", "precision")))
        show_rows([best], f"{target.upper()} — sélection sur validation")
        metrics = [r for r in read_rows(directory / "metrics" / f"{target}_metrics.csv") if r.get("split") == "test" and r.get("model") == best["model"]]
        show_rows(metrics, "Test Kubernetes — modèle sélectionné")
        matrices = [r for r in read_rows(directory / "metrics" / f"{target}_confusion_matrix.csv") if r.get("split") == "test" and r.get("model") == best["model"]]
        show_confusions(matrices, f"{framework} {target.upper()} — apprentissage Kubernetes")


### Entraînement Kubernetes — guidance

UNDER : aucun candidat enregistré (UNDER n'a pas de positifs ici).

**OVER — sélection sur validation**

model,selection_split,split,dataset,threshold,n,positives,negatives,accuracy,precision,recall,f1,roc_auc,pr_auc,balanced_accuracy
random_forest_leaf1_sqrt,validation,validation,all,0.6,250,125,125,0.936,0.957983,0.912,0.934426,0.965824,0.96618,0.936


**Test Kubernetes — modèle sélectionné**

...

model,selection_split,split,dataset,threshold,n,positives,negatives,accuracy,precision,recall,f1,roc_auc,pr_auc,balanced_accuracy
random_forest_leaf2_sqrt,validation,validation,all,0.71,244,28,216,0.954918,1,0.607143,0.755556,0.935847,0.759035,0.803571


**Test Kubernetes — modèle sélectionné**

model,split,dataset,threshold,n,positives,negatives,accuracy,precision,recall,f1,roc_auc,pr_auc,balanced_accuracy
random_forest_leaf2_sqrt,test,all,0.71,243,31,212,0.90535,0.653846,0.548387,0.596491,0.853926,0.626351,0.752967


**outlines OVER — apprentissage Kubernetes — random_forest_leaf2_sqrt test**

Vérité / Prédiction,Négatif,Positif
Négatif (pas d'erreur),203,9
Positif (UNDER ou OVER),14,17


## Lecture des résultats

- Les données manquantes sont signalées ; un dossier absent n'est pas un score nul.
- Les sorties EDA et raffinées correspondent au dataset choisi ; les modèles GitHub sont évalués sur leurs propres schémas de test sauvegardés.
- Les scores recalculés et les scores historiques sont séparés. Les matrices ont la vérité en lignes et les prédictions en colonnes ; la classe positive signifie une erreur UNDER ou OVER.
- Les règles montrent des associations interprétables, pas des preuves de causalité.
- Pour conserver un notebook léger, enregistrer sans les sorties volumineuses des galeries après consultation.
